# **Project Work finale** – Corso Data Science and Generative AI (OVED627)  

### **Obiettivo** per questo capitolo

L'obiettivo dell'esercitazione è analizzare un dataset contenente i tick della criptovaluta **Bitcoin** per:

Applicare modelli di Machine Learning per:
- Stimare il **Fear & Greed Index** (indicatore del sentiment di mercato)

###**Fase di ricerca** - Cap 3
3. Analisi predittiva del fear and greed index tramite algoritmi ML/NN

## 0. Import

In [1]:
!pip install kaleido -q
import kaleido #required
kaleido.__version__ #0.2.1

import plotly
plotly.__version__ #5.5.0

import plotly.graph_objects as go
import plotly.express as px
import plotly.figure_factory as ff
from plotly.subplots import make_subplots

   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 79.9/79.9 MB 7.2 MB/s eta 0:00:00


In [2]:
import pandas as pd
from datetime import datetime, timedelta
import matplotlib.pyplot as plt
import seaborn as sns
import numpy as np
sns.set_theme()

In [3]:
#Tensorflow
import tensorflow
from tensorflow.keras.models import load_model, Sequential
from tensorflow.keras.layers import LSTM, Dense, Input, Dropout
from tensorflow.keras.optimizers import Adam
from tensorflow.keras import backend as K
from tensorflow.keras.regularizers import l1_l2
from tensorflow.keras.callbacks import ReduceLROnPlateau, EarlyStopping
from tensorflow.keras.metrics import R2Score

import pickle

In [4]:
#SKLEARN
from sklearn.preprocessing import StandardScaler, MinMaxScaler, PolynomialFeatures
from sklearn.pipeline import make_pipeline
from sklearn.decomposition import PCA
from sklearn.linear_model import Ridge, Lasso, ElasticNet, HuberRegressor, QuantileRegressor, RANSACRegressor, TheilSenRegressor, LinearRegression, BayesianRidge
from sklearn.tree import DecisionTreeRegressor
from sklearn.ensemble import RandomForestRegressor, GradientBoostingRegressor, AdaBoostRegressor
from sklearn.svm import SVR
from sklearn.neighbors import KNeighborsRegressor
from sklearn.neural_network import MLPRegressor
from sklearn.model_selection import KFold, cross_val_score, TimeSeriesSplit, GridSearchCV, train_test_split
from sklearn.metrics import (
    mean_squared_error,
    mean_absolute_error,
    r2_score,
    average_precision_score,
    accuracy_score,
    balanced_accuracy_score,
    classification_report,
    confusion_matrix
)

In [5]:
from lightgbm import LGBMClassifier

In [6]:
#Stats model: per VIF e Modelli Lineari
import statsmodels.api as sm
from statsmodels.stats.outliers_influence import variance_inflation_factor
from scipy.stats import t

In [177]:
#############################
#   Import da Colab
#############################

#from google.colab import drive
#drive.mount('/content/drive')
#data_merged = pd.read_csv('/content/drive/MyDrive/Data Science/Machine e Deep Learning/OVED627/Dataset e consegna/merged_fix_to_hour.csv')

import zipfile
import os
import requests
from io import BytesIO

url = "https://github.com/FedeGambe/Bitcoin_Prediction/raw/main/Materiali/Datasets.zip"
response = requests.get(url) # Scarica il file ZIP

if response.status_code == 200: #check per vedere se è avvenuto con successo
    with zipfile.ZipFile(BytesIO(response.content)) as zip_ref: #temp folder per la decompressione
        zip_ref.extractall("cartella_decompressa") #estrazione file

        extracted_files = zip_ref.namelist() # Lista dei file estratti
        print(f"File estratti: {extracted_files}")

        csv_file_name = "merged_fix_to_hour.csv" #file da estrarre
        if csv_file_name in extracted_files:
            csv_file_path = os.path.join("cartella_decompressa", csv_file_name)
            data_merged = pd.read_csv(csv_file_path)
            print(f"\nPrimi 5 record del CSV '{csv_file_name}':")
            print(data_merged.head())
        else:
            print(f"Il file {csv_file_name} non è stato trovato nella cartella decompressa.")
else:
    print("Errore nel download del file ZIP.")

<class 'pandas.core.frame.DataFrame'>
RangeIndex: 17515 entries, 0 to 17514
Columns: 131 entries, Datetime to google_trends_bitcoin
dtypes: float64(128), int64(2), object(1)
memory usage: 17.5+ MB


In [179]:
columns_BTC = [col for col in data_merged.columns if col.startswith('BTC') or col == 'Datetime']
df = data_merged[columns_BTC]
df.info()

<class 'pandas.core.frame.DataFrame'>
RangeIndex: 17515 entries, 0 to 17514
Data columns (total 6 columns):
 #   Column              Non-Null Count  Dtype  
---  ------              --------------  -----  
 0   Datetime            17515 non-null  object 
 1   BTC_USDT_1h_open    17515 non-null  float64
 2   BTC_USDT_1h_high    17515 non-null  float64
 3   BTC_USDT_1h_low     17515 non-null  float64
 4   BTC_USDT_1h_close   17515 non-null  float64
 5   BTC_USDT_1h_volume  17515 non-null  float64
dtypes: float64(5), object(1)
memory usage: 821.1+ KB


## 3. Fear Index - Sentiment Analysis

Variabili Sentiment & psychology: Fear & Greed Index, Google Trends, BTC dominance

### 3.1. Preparazione per l'analisi

#### Preparazione dataset

In [235]:
columns_to_keep_df_sent = []
for col in data_merged.columns:
    col_lower = col.lower()
    if any(key in col_lower for key in ['open', 'high', 'low']) and 'close' not in col_lower:
        continue
    columns_to_keep_df_sent.append(col)

df_sent_with_dt = data_merged[columns_to_keep_df_sent]
print("Colonne mantenute in df_sent_with_dt:")
print(df_sent_with_dt.columns.tolist())

Colonne mantenute in df_sent_with_dt:
['Datetime', 'BNB_USDT_1h_close', 'BNB_USDT_1h_volume', 'BTC_USDT_1h_close', 'BTC_USDT_1h_volume', 'DOGE_USDT_1h_close', 'DOGE_USDT_1h_volume', 'ETH_USDT_1h_close', 'ETH_USDT_1h_volume', 'SOL_USDT_1h_close', 'SOL_USDT_1h_volume', 'XRP_USDT_1h_close', 'XRP_USDT_1h_volume', 'cattle_Close LE=F', 'cattle_Volume LE=F', 'corn_Close ZC=F', 'corn_Volume ZC=F', 'crude_Close CL=F', 'crude_Volume CL=F', 'gold_Close GC=F', 'gold_Volume GC=F', 'silver_Close SI=F', 'silver_Volume SI=F', 'soybeans_Close ZS=F', 'soybeans_Volume ZS=F', 'wheat_Close ZW=F', 'wheat_Volume ZW=F', 'CAC_Close ^FCHI', 'CAC_Volume ^FCHI', 'DAX_Close ^GDAXI', 'DAX_Volume ^GDAXI', 'Dow_Close ^DJI', 'Dow_Volume ^DJI', 'EURO_Close ^STOXX50E', 'EURO_Volume ^STOXX50E', 'FTSE_Close ^FTSE', 'FTSE_Volume ^FTSE', 'IBOVESPA_Close ^BVSP', 'IBOVESPA_Volume ^BVSP', 'IPC_Close ^MXX', 'IPC_Volume ^MXX', 'NASDAQ_Close ^IXIC', 'NASDAQ_Volume ^IXIC', 'Russell_Close ^RUT', 'Russell_Volume ^RUT', 'S&P_Close ^G

In [236]:
df_sent_with_dt['Datetime'] = pd.to_datetime(df_sent_with_dt['Datetime'])

df_sent = df_sent_with_dt.drop(columns=['Datetime'])
df_sent.head()

,BNB_USDT_1h_close,BNB_USDT_1h_volume,BTC_USDT_1h_close,BTC_USDT_1h_volume,DOGE_USDT_1h_close,DOGE_USDT_1h_volume,ETH_USDT_1h_close,ETH_USDT_1h_volume,SOL_USDT_1h_close,SOL_USDT_1h_volume,...,S&P_Close ^GSPC,S&P_Volume ^GSPC,S&P_Close ^GSPTSE,S&P_Volume ^GSPTSE,VIX_Close ^VIX,VIX_Volume ^VIX,funding_rate,fear_gread_index,google_trends_buy_crypto,google_trends_bitcoin
0,332.3852,80.49008,30277.44,28.928997,0.08903,5158881.9,2089.59,913.36549,24.12,7143.016,...,4139.490234,0.0,20583.220703,0.0,17.59,0.0,0.0001,68.0,20,33
1,332.1377,335.75052,30240.00,102.212972,0.08860,7483794.0,2089.27,3163.40658,24.16,11060.995,...,4139.490234,0.0,20583.220703,0.0,17.59,0.0,0.0001,68.0,20,33
2,332.2934,88.40229,30267.06,27.901720,0.08896,1545046.8,2088.71,784.07128,24.47,14237.101,...,4139.490234,0.0,20583.220703,0.0,17.59,0.0,0.0001,68.0,20,33
3,332.2009,59.45825,30248.96,36.337277,0.08918,6372161.7,2086.26,657.06335,24.33,6774.569,...,4139.490234,0.0,20583.220703,0.0,17.59,0.0,0.0001,68.0,20,33
4,333.0055,115.57138,30302.08,41.767970,0.09038,15659974.2,2097.00,1598.29132,24.44,6977.738,...,4139.490234,0.0,20583.220703,0.0,17.59,0.0,0.0001,68.0,20,33


In [237]:
df_sent.info()

<class 'pandas.core.frame.DataFrame'>
RangeIndex: 17515 entries, 0 to 17514
Data columns (total 54 columns):
 #   Column                    Non-Null Count  Dtype  
---  ------                    --------------  -----  
 0   BNB_USDT_1h_close         17515 non-null  float64
 1   BNB_USDT_1h_volume        17515 non-null  float64
 2   BTC_USDT_1h_close         17515 non-null  float64
 3   BTC_USDT_1h_volume        17515 non-null  float64
 4   DOGE_USDT_1h_close        17515 non-null  float64
 5   DOGE_USDT_1h_volume       17515 non-null  float64
 6   ETH_USDT_1h_close         17515 non-null  float64
 7   ETH_USDT_1h_volume        17515 non-null  float64
 8   SOL_USDT_1h_close         17515 non-null  float64
 9   SOL_USDT_1h_volume        17515 non-null  float64
 10  XRP_USDT_1h_close         17515 non-null  float64
 11  XRP_USDT_1h_volume        17515 non-null  float64
 12  cattle_Close LE=F         17515 non-null  float64
 13  cattle_Volume LE=F        17515 non-null  float64
 14  corn_C

#### Correlazione Features con Target

In [238]:
abbreviated_columns = [
    "BNB_close", "BNB_vol","BTC_close", "BTC_vol","DOGE_close", "DOGE_vol","ETH_close", "ETH_vol","SOL_close", "SOL_vol","XRP_close", "XRP_vol",
    "cattle_close", "cattle_vol","corn_close", "corn_vol","crude_close", "crude_vol","gold_close", "gold_vol","silver_close", "silver_vol","soybeans_close", "soybeans_vol","wheat_close", "wheat_vol",
    "CAC_close", "CAC_vol","DAX_close", "DAX_vol","Dow_close", "Dow_vol","EURO_close", "EURO_vol","FTSE_close", "FTSE_vol","IBOVESPA_close", "IBOVESPA_vol","IPC_close", "IPC_vol","NASDAQ_close", "NASDAQ_vol","Russell_close", "Russell_vol","S&P_close_1", "S&P_vol_1","S&P_close_2", "S&P_vol_2","VIX_close", "VIX_vol",
    "funding_rate",
    "trends_buy_crypto","trends_bitcoin"
]

In [242]:
# Calcolo della matrice di correlazione
corr_matrix = df_sent.corr()
target_corr = corr_matrix['fear_gread_index'].drop('fear_gread_index')
target_corr_sorted = target_corr.reindex(target_corr.abs().sort_values(ascending=False).index)

corr_df = pd.DataFrame({
    'Variabile': target_corr_sorted.index,
    'Correlazione': target_corr_sorted.values,
})


fig = px.bar(corr_df,x='Correlazione',y='Variabile',
    orientation='h',
    color='Correlazione', color_continuous_scale='RdBu')

fig.update_layout(title={'text': "Correlazione delle feature con Fear & Greed Index",'x': 0.5,
                         'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'},},
                  yaxis=dict(autorange="reversed"),  height=1000, width=1200, )
fig.write_image("correlazione_fear_greed_index.png")
fig.show()

In [240]:
significant_features = target_corr[abs(target_corr) > 0.1].index.tolist()
print("Variabili significative:", significant_features)

Variabili significative: ['BNB_USDT_1h_close', 'BNB_USDT_1h_volume', 'BTC_USDT_1h_close', 'DOGE_USDT_1h_close', 'DOGE_USDT_1h_volume', 'ETH_USDT_1h_close', 'SOL_USDT_1h_close', 'SOL_USDT_1h_volume', 'XRP_USDT_1h_volume', 'cattle_Close LE=F', 'gold_Close GC=F', 'CAC_Close ^FCHI', 'Dow_Close ^DJI', 'Dow_Volume ^DJI', 'FTSE_Close ^FTSE', 'IPC_Close ^MXX', 'IPC_Volume ^MXX', 'NASDAQ_Close ^IXIC', 'Russell_Close ^RUT', 'S&P_Volume ^GSPC', 'S&P_Volume ^GSPTSE', 'VIX_Close ^VIX', 'funding_rate', 'google_trends_buy_crypto', 'google_trends_bitcoin']


Per iniziare l’analisi predittiva su
fear and greed index osserviamo
la matrice di correlazione tra la
variabile di interesse e le altre
features.

In [241]:
correlazioni = df_sent.corr()
correlazioni_target = correlazioni["fear_gread_index"].sort_values(ascending=False)
top_features = correlazioni_target.abs().sort_values(ascending=False).head(30).index.tolist()
top_features

['fear_gread_index',
 'ETH_USDT_1h_close',
 'google_trends_buy_crypto',
 'google_trends_bitcoin',
 'VIX_Close ^VIX',
 'DOGE_USDT_1h_close',
 'SOL_USDT_1h_close',
 'DOGE_USDT_1h_volume',
 'Russell_Close ^RUT',
 'Dow_Volume ^DJI',
 'BTC_USDT_1h_close',
 'IPC_Volume ^MXX',
 'S&P_Volume ^GSPC',
 'BNB_USDT_1h_volume',
 'funding_rate',
 'XRP_USDT_1h_volume',
 'S&P_Volume ^GSPTSE',
 'BNB_USDT_1h_close',
 'IPC_Close ^MXX',
 'FTSE_Close ^FTSE',
 'gold_Close GC=F',
 'Dow_Close ^DJI',
 'CAC_Close ^FCHI',
 'SOL_USDT_1h_volume',
 'NASDAQ_Close ^IXIC',
 'cattle_Close LE=F',
 'BTC_USDT_1h_volume',
 'S&P_Close ^GSPC',
 'silver_Close SI=F',
 'DAX_Close ^GDAXI']

#### Correlazione tra le Features

In [126]:
features = df_sent.drop(columns=['fear_gread_index'])
correlation_matrix = features.corr()
original_columns = list(correlation_matrix.columns)

In [127]:
fig_cm = go.Figure(data=go.Heatmap(z=correlation_matrix.values,x=abbreviated_columns,y=abbreviated_columns,
        colorscale='RdBu',reversescale=False,colorbar=dict(title="Correlation")))
fig_cm.update_layout(
    title={'text': "Correlation Matrix",'x': 0.5,'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'},},
    margin=dict(t=200, b=0, l=0, r=0),height=800,width=1200,)
fig_cm.show()

In [128]:
columns_to_drop = [col for col in features.columns if 'vol' in col.lower()]
features_no_vol = features.drop(columns=columns_to_drop)
features_no_vol.columns

Index(['BNB_USDT_1h_close', 'BTC_USDT_1h_close', 'DOGE_USDT_1h_close',
       'ETH_USDT_1h_close', 'SOL_USDT_1h_close', 'XRP_USDT_1h_close',
       'cattle_Close LE=F', 'corn_Close ZC=F', 'crude_Close CL=F',
       'gold_Close GC=F', 'silver_Close SI=F', 'soybeans_Close ZS=F',
       'wheat_Close ZW=F', 'CAC_Close ^FCHI', 'DAX_Close ^GDAXI',
       'Dow_Close ^DJI', 'EURO_Close ^STOXX50E', 'FTSE_Close ^FTSE',
       'IBOVESPA_Close ^BVSP', 'IPC_Close ^MXX', 'NASDAQ_Close ^IXIC',
       'Russell_Close ^RUT', 'S&P_Close ^GSPC', 'S&P_Close ^GSPTSE',
       'VIX_Close ^VIX', 'funding_rate', 'google_trends_buy_crypto',
       'google_trends_bitcoin'],
      dtype='object')

In [129]:
abbreviated_columns_no_vol = [
    "BNB_close", "BTC_close","DOGE_close","ETH_close","SOL_close","XRP_close",
    "cattle_close","corn_close","crude_close","gold_close","silver_close","soybeans_close","wheat_close",
    "CAC_close","DAX_close","Dow_close","EURO_close","FTSE_close","IBOVESPA_close","IPC_close","NASDAQ_close","Russell_close","S&P_close_1","S&P_close_2","VIX_close",
    "funding_rate",
    "trends_buy_crypto","trends_bitcoin"
]


In [130]:
#df_sent = df_sent.drop(columns=columns_to_drop)
features = df_sent.drop(columns=['fear_gread_index'])

In [131]:
correlation_matrix = features_no_vol.corr()
original_columns = list(correlation_matrix.columns)
fig_cm = ff.create_annotated_heatmap(z=correlation_matrix.values, x=abbreviated_columns_no_vol, y=abbreviated_columns_no_vol,
    annotation_text=np.around(correlation_matrix.values, decimals=2),showscale=True, colorscale='RdBu')
fig_cm.update_layout(
    title={'text': "Correlation Matrix",'x': 0.5,'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'},},
    margin=dict(t=200, b=0, l=0, r=0),height=800,width=1500,)
fig_cm.show()

In [132]:
#ANALISI VIF
X = df_sent.drop(columns = ['fear_gread_index'])
X_const = sm.add_constant(X)

# Calcolo VIF
vif_data = pd.DataFrame()
vif_data["feature"] = X.columns
vif_data["VIF"] = [variance_inflation_factor(X_const.values, i+1) for i in range(len(X.columns))]  # i+1 per saltare la costante
print(vif_data)

/usr/local/lib/python3.11/dist-packages/statsmodels/regression/linear_model.py:1782: RuntimeWarning:

invalid value encountered in scalar divide



                     feature          VIF
0          BNB_USDT_1h_close    70.242282
1         BNB_USDT_1h_volume     1.895809
2          BTC_USDT_1h_close   265.739777
3         BTC_USDT_1h_volume     3.233976
4         DOGE_USDT_1h_close    42.684455
5        DOGE_USDT_1h_volume     2.711729
6          ETH_USDT_1h_close    36.686604
7         ETH_USDT_1h_volume     3.537444
8          SOL_USDT_1h_close    64.033253
9         SOL_USDT_1h_volume     2.973622
10         XRP_USDT_1h_close    32.409949
11        XRP_USDT_1h_volume     2.262198
12         cattle_Close LE=F     7.098737
13        cattle_Volume LE=F     1.228298
14           corn_Close ZC=F    14.886450
15          corn_Volume ZC=F     1.737581
16          crude_Close CL=F     5.788216
17         crude_Volume CL=F     1.340125
18           gold_Close GC=F   196.096051
19          gold_Volume GC=F     3.763759
20         silver_Close SI=F    44.272424
21        silver_Volume SI=F     3.863778
22       soybeans_Close ZS=F    23

#### PCA

In [133]:
features = features_no_vol

In [134]:
scaler = StandardScaler()
X_scaled = scaler.fit_transform(features)

pca = PCA() #PCA senza ridurre il numero di componenti
X_pca = pca.fit(X_scaled)
explained_variance = X_pca.explained_variance_ratio_ #calcolo la varianza spiegata da ciascuna componente

In [135]:
# Numero di componenti che spiegano la % della varianza
percentuale_var = 0.90
cumulative_variance = X_pca.explained_variance_ratio_.cumsum()
n_components = (cumulative_variance >= percentuale_var).argmax() + 1
print(f"Numero di componenti che spiegano il {percentuale_var} della varianza: {n_components}")

Numero di componenti che spiegano il 0.9 della varianza: 6


In [136]:
fig_pca = go.Figure()

# Aggiungiamo la traccia per la "Varianza Spiegata" (sinistra)
fig_pca.add_trace(go.Scatter(x=list(range(1, len(explained_variance) + 1)), y=explained_variance,
                             mode='lines+markers', marker=dict(color='#636EFA'), name='Varianza Spiegata',
                             hovertemplate='%{x}<br>Varianza Spiegata: %{y:.4f}<extra></extra>'))

# Aggiungiamo la traccia per la "Varianza Cumulativa" (destra)
fig_pca.add_trace(go.Scatter(x=list(range(1, len(explained_variance) + 1)), y=explained_variance.cumsum(),
                             mode='lines+markers', marker=dict(color='#EF553B'), name='Varianza Cumulativa',
                             hovertemplate='%{x}<br>Varianza Cumulativa: %{y:.4f}<extra></extra>',
                             yaxis="y2"))

# Linea orizzontale a 95% sulla y2
y_value_percent = percentuale_var * explained_variance.sum()  # 95% del totale della varianza cumulativa
#fig_pca.add_trace(go.Scatter(x=[1, len(explained_variance)], y=[y_value_percent, y_value_percent],mode='lines', line=dict(color='gray', dash='dash', width=1), name=f'Linea {round(y_value_percent,4)*100}% Varianza Cumulativa'))
fig_pca.add_shape(type='line',y0=percentuale_var,y1=percentuale_var,x0=0,x1=1,xref='paper', yref='y2',line=dict(color='gray', dash='dash', width=1), name=f'Linea {round(y_value_percent,4)*100}% Varianza Cumulativa')

#punto di intersezione tra la curva di varianza cumulativa e la linea orizzontale
cumulative_variance = explained_variance.cumsum()
x_intersection = np.argmax(cumulative_variance >= y_value_percent) + 1  # Aggiungiamo 1 perché gli indici partono da 0
y_intersection = cumulative_variance[x_intersection - 1]  # Otteniamo il valore della varianza cumulativa al punto di intersezione

#Linea verticale perpendicolare (passante per il punto di intersezione)
fig_pca.add_trace(go.Scatter(x=[x_intersection, x_intersection], y=[0, y_intersection],
                             mode='lines', line=dict(color='gray', dash='dash', width=1), name='Linea Perpendicolare', showlegend=False))

fig_pca.update_layout(
    title={'text': "Analisi PCA - Varianza per Componente", 'x': 0.5, 'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'}},
    showlegend=True, width=1200, height=600,
    yaxis=dict(title="Varianza Spiegata", titlefont=dict(color="#636EFA")),
    yaxis2=dict(title="Varianza Cumulativa", titlefont=dict(color="orangered"), overlaying="y", side="right"),
    xaxis=dict(title="Numero di Componente",dtick=1, tickvals=list(range(1, len(explained_variance) + 1)) ),
    legend=dict(x=1.05, xanchor='left', yanchor='middle'),
    template='plotly_dark'
)

fig_pca.show()

In [137]:
components = X_pca.components_[:n_components] # Prendi i carichi delle prime 'n_components' componenti
var_names = features.columns
pesi_var_pca = pd.DataFrame(components, columns=var_names) #DataFrame con i carichi delle variabili
pesi_var_pca.round(4)
print("Carichi delle variabili per le componenti selezionate:")
pesi_var_pca

Carichi delle variabili per le componenti selezionate:


,BNB_USDT_1h_close,BTC_USDT_1h_close,DOGE_USDT_1h_close,ETH_USDT_1h_close,SOL_USDT_1h_close,XRP_USDT_1h_close,cattle_Close LE=F,corn_Close ZC=F,crude_Close CL=F,gold_Close GC=F,...,IBOVESPA_Close ^BVSP,IPC_Close ^MXX,NASDAQ_Close ^IXIC,Russell_Close ^RUT,S&P_Close ^GSPC,S&P_Close ^GSPTSE,VIX_Close ^VIX,funding_rate,google_trends_buy_crypto,google_trends_bitcoin
0,0.231011,0.239044,0.199030,0.168385,0.230991,0.166647,0.168565,-0.145546,-0.101208,0.223727,...,0.146261,-0.054469,0.237726,0.220510,0.240766,0.237138,0.045973,0.089186,0.154434,0.135186
1,0.054784,-0.044336,-0.108284,0.293642,0.120418,-0.330586,-0.209837,-0.243133,0.206516,-0.143942,...,0.240003,0.385474,0.029469,0.101314,0.029093,-0.078555,-0.343844,0.399907,-0.043830,0.016522
2,-0.020677,0.084849,0.340002,0.252437,0.110781,0.123623,-0.068304,0.107559,0.096767,-0.190790,...,-0.191724,-0.085198,-0.001153,0.075891,-0.032959,-0.032925,-0.276303,-0.081352,0.490148,0.445677
3,0.043120,0.052718,0.066747,0.010015,-0.031613,0.203811,-0.054097,0.428982,-0.149584,0.023077,...,-0.158737,0.369090,-0.045879,-0.027993,-0.042071,0.045348,-0.175721,-0.240298,0.024253,-0.032334
4,0.032802,0.042957,-0.008963,0.073776,-0.009997,0.151347,0.430419,-0.055788,0.708407,-0.045404,...,-0.211704,-0.080590,-0.002252,-0.148266,-0.024124,-0.073811,-0.059271,-0.096410,-0.078562,-0.134452
5,-0.188919,0.010101,-0.115089,-0.149699,-0.035864,0.124380,0.171464,-0.196532,-0.133538,-0.023095,...,0.412599,0.378841,-0.075295,-0.102287,-0.062539,-0.066462,0.162646,-0.331537,0.093809,0.292195


In [138]:
#Le variabili più significative per ogni componente
for i in range(n_components):
    top_features = pesi_var_pca.iloc[i].sort_values(ascending=False).head(30)
    print(f"\nLe variabili più significative per la componente {i+1}:")
    print(top_features)


Le variabili più significative per la componente 1:
S&P_Close ^GSPC             0.240766
Dow_Close ^DJI              0.239818
BTC_USDT_1h_close           0.239044
NASDAQ_Close ^IXIC          0.237726
S&P_Close ^GSPTSE           0.237138
BNB_USDT_1h_close           0.231011
SOL_USDT_1h_close           0.230991
DAX_Close ^GDAXI            0.227706
gold_Close GC=F             0.223727
Russell_Close ^RUT          0.220510
EURO_Close ^STOXX50E        0.219601
silver_Close SI=F           0.214642
FTSE_Close ^FTSE            0.213588
DOGE_USDT_1h_close          0.199030
cattle_Close LE=F           0.168565
ETH_USDT_1h_close           0.168385
XRP_USDT_1h_close           0.166647
google_trends_buy_crypto    0.154434
IBOVESPA_Close ^BVSP        0.146261
google_trends_bitcoin       0.135186
CAC_Close ^FCHI             0.122389
funding_rate                0.089186
VIX_Close ^VIX              0.045973
IPC_Close ^MXX             -0.054469
crude_Close CL=F           -0.101208
wheat_Close ZW=F      

1. Global Market Movement (S&P, Dow, NASDAQ, BTC)
 - **Motivazione**: La Componente 1 è fortemente influenzata da indici azionari globali come il S&P 500, il Dow Jones, il NASDAQ e Bitcoin. Queste variabili suggeriscono una forte correlazione con i movimenti di mercato globali, in particolare quelli azionari e di criptovalute. Le principali variabili in questa componente sono tutte relative a indici di mercato finanziario, indicando che questa componente cattura le tendenze generali del mercato.

 - **Implicazioni**: Questa componente riflette i movimenti di mercato globali e può essere utile per analizzare l’andamento complessivo degli asset tradizionali e di criptovalute.

2. Market Sentiment and Funding Rates
 - **Motivazione**: La Componente 2 è dominata da variabili come il funding rate, l’IPC (Indice dei Prezzi al Consumo) e il VIX (Indice di Volatilità), che misurano il sentiment del mercato e la percezione del rischio. Questi fattori sono spesso utilizzati per analizzare la stabilità del mercato e l’andamento dell’inflazione e dei tassi di interesse.

 - **Implicazioni**: Questa componente suggerisce che le variabili legate al sentiment e alla percezione del rischio sono cruciali per determinare il comportamento degli asset finanziari, con un’enfasi sul rischio sistemico (rappresentato dal VIX) e sul rischio di liquidità (rappresentato dal funding rate).

3. Crypto Search Trends and Sentiment
 - **Motivazione**: La Componente 3 è influenzata principalmente dalle tendenze di ricerca su Google relative a criptovalute come Bitcoin e Dogecoin, nonché dal sentiment del mercato misurato tramite google_trends_buy_crypto. Questo suggerisce che questa componente cattura la reattività del mercato e delle ricerche online rispetto alle criptovalute, un fenomeno che è diventato sempre più importante nelle decisioni di investimento.

 - **Implicazioni**: Questa componente riflette l’adozione e l’interesse del pubblico nelle criptovalute, indicando come il sentiment e le tendenze di ricerca online possano influenzare l’andamento del mercato crypto.

4. Commodity and Equity Market Dynamics
 - **Motivazione**: La Componente 4 è dominata da commodity come il corn, il wheat e il CAC 40 (indice azionario francese), insieme a XRP (una criptovaluta) e vari altri indici azionari. Questi fattori suggeriscono una correlazione tra l’andamento dei mercati azionari e delle commodities, con un focus sulle dinamiche dei mercati internazionali.

 - **Implicazioni**:Questa componente potrebbe essere utilizzata per analizzare come i mercati delle commodities e delle azioni interagiscono e influenzano l’economia globale, con una particolare attenzione agli sviluppi in Europa e in mercati emergenti.

5. Commodities Price Movements
 - **Motivazione**: La Componente 5 è fortemente influenzata da commodities come il crude oil (petrolio), il cattle (bovini), e il wheat (grano), ma anche da indici azionari come il CAC 40. Questi fattori mostrano una correlazione forte tra i prezzi delle commodities e i mercati finanziari, indicando che il movimento dei prezzi delle materie prime potrebbe avere un impatto significativo sui mercati azionari.

 - **Implicazioni**: Questa componente può essere utilizzata per analizzare i movimenti dei prezzi delle commodities e la loro relazione con i mercati azionari e le economie emergenti. È particolarmente utile per chi investe in materie prime o per analizzare i trend economici globali.

6. Emerging Market and Macro Trends
 - **Motivazione**: La Componente 6 è dominata da variabili legate agli emerging markets (mercati emergenti) come l’IBOVESPA (indice brasiliano) e l’IPC (Indice dei Prezzi al Consumo). Questi fattori suggeriscono che questa componente riflette le dinamiche macroeconomiche e i mercati emergenti, con particolare attenzione ai fattori inflazionistici e ai tassi di interesse.

 - **Implicazioni**: Questa componente è utile per analizzare l’andamento dei mercati emergenti e l’impatto di variabili macroeconomiche su questi mercati. È importante per chi è interessato agli investimenti nei mercati emergenti o agli sviluppi macroeconomici globali.

In [139]:
X_pca = pca.transform(X_scaled)  # Trasformazione delle componenti principali con PCA
pca_df = pd.DataFrame(X_pca[:, :n_components], columns=[f'PC{i+1}' for i in range(n_components)])

pca_component_names = [
    "Global Market Movement",                           # Componente 1
    "Market Sentiment and Funding Rates",               # Componente 2
    "Crypto Search Trends and Sentiment",               # Componente 3
    "Commodity and Equity Market Dynamics",             # Componente 4
    "Commodities Price Movements",                      # Componente 5
    "Emerging Market and Macro Trends"                  # Componente 6
]

pca_df.columns = pca_component_names[:n_components] # Rinomina le colonne
pca_df['fear_gread_index'] = df_sent['fear_gread_index'].values
pca_df.head()

,Global Market Movement,Market Sentiment and Funding Rates,Crypto Search Trends and Sentiment,Commodity and Equity Market Dynamics,Commodities Price Movements,Emerging Market and Macro Trends,fear_gread_index
0,-5.523296,-0.862284,0.682938,2.753630,0.178026,-1.742221,68.0
1,-5.525302,-0.860945,0.680905,2.752594,0.177492,-1.741749,68.0
2,-5.523137,-0.861141,0.682591,2.752850,0.177472,-1.742348,68.0
3,-5.524784,-0.861159,0.681662,2.752049,0.176480,-1.742489,68.0
4,-5.517080,-0.859006,0.690565,2.754121,0.178329,-1.746639,68.0


In [140]:
pca_df.info()

<class 'pandas.core.frame.DataFrame'>
RangeIndex: 17515 entries, 0 to 17514
Data columns (total 7 columns):
 #   Column                                Non-Null Count  Dtype  
---  ------                                --------------  -----  
 0   Global Market Movement                17515 non-null  float64
 1   Market Sentiment and Funding Rates    17515 non-null  float64
 2   Crypto Search Trends and Sentiment    17515 non-null  float64
 3   Commodity and Equity Market Dynamics  17515 non-null  float64
 4   Commodities Price Movements           17515 non-null  float64
 5   Emerging Market and Macro Trends      17515 non-null  float64
 6   fear_gread_index                      17515 non-null  float64
dtypes: float64(7)
memory usage: 958.0 KB


In [141]:
#ANALISI VIF
X = pca_df.drop(columns = ['fear_gread_index'])
X_const = sm.add_constant(X)

# Calcolo VIF
vif_data = pd.DataFrame()
vif_data["feature"] = X.columns
vif_data["VIF"] = [variance_inflation_factor(X_const.values, i+1) for i in range(len(X.columns))]  # i+1 per saltare la costante
print(vif_data)

                                feature  VIF
0                Global Market Movement  1.0
1    Market Sentiment and Funding Rates  1.0
2    Crypto Search Trends and Sentiment  1.0
3  Commodity and Equity Market Dynamics  1.0
4           Commodities Price Movements  1.0
5      Emerging Market and Macro Trends  1.0


In [142]:
#Verifica se ha mantenuto l'ordine delle righe
print(df_sent['fear_gread_index'].head(-5))
print(pca_df['fear_gread_index'].head(-5))

0        68.0
1        68.0
2        68.0
3        68.0
4        68.0
         ... 
17505    31.0
17506    31.0
17507    31.0
17508    31.0
17509    31.0
Name: fear_gread_index, Length: 17510, dtype: float64
0        68.0
1        68.0
2        68.0
3        68.0
4        68.0
         ... 
17505    31.0
17506    31.0
17507    31.0
17508    31.0
17509    31.0
Name: fear_gread_index, Length: 17510, dtype: float64


In [143]:
df_ridotto = pca_df

- Componente 1: Rappresenta i movimenti generali dei mercati finanziari globali.
- Componente 2: Rappresenta il sentiment di mercato, inclusi rischi sistemici e inflazione.
- Componente 3: Rappresenta l'interesse e il sentiment delle criptovalute, attraverso le ricerche online.
- Componente 4: Analizza la dinamica tra commodities e mercati azionari.
- Componente 5: Si concentra sulle fluttuazioni dei prezzi delle commodities e il loro impatto sui mercati finanziari.
- Componente 6: Rappresenta le tendenze macroeconomiche e i mercati emergenti.

#### Train and test

In [144]:
y = pca_df['fear_gread_index']
X = pca_df.drop(columns=['fear_gread_index'])

X_train, X_test, y_train, y_test = train_test_split(X, y, test_size=0.2, random_state=343)
sc = StandardScaler()
X_train = sc.fit_transform(X_train)
X_test = sc.transform(X_test)
print("La shape di X è:", X.shape)
print("La shape di y è:", y.shape)

La shape di X è: (17515, 6)
La shape di y è: (17515,)


### 3.2. Analisi

#### Confronto Algorimti di regressione

Come introduzione
sono stati testati
modelli di
regressione e sono
indicati media e
MSE nel grafico.
L’algoritmo scelto è
stato il «Random
Forest» dato che
presentava un
R_squared
maggiore ed un
MSE minore.

In [ ]:
models = [
    ('Linear Regression', LinearRegression()),
    ('Ridge Regression', Ridge()),
    ('Lasso Regression', Lasso()),
    ('Elastic Net Regression', ElasticNet()),
    ('Decision Tree Regression', DecisionTreeRegressor()),
    ('Random Forest Regression', RandomForestRegressor()),
    ('Gradient Boosting Regression', GradientBoostingRegressor()),
    ('AdaBoost Regression', AdaBoostRegressor()),
    ('Support Vector Regression', SVR()),
    ('K-Nearest Neighbors Regression', KNeighborsRegressor()),
    ('MLP Regression', MLPRegressor()),
    ('Huber Regression', HuberRegressor()),
    ('Quantile Regression', QuantileRegressor()),
    ('RANSAC Regression', RANSACRegressor()),
    ('TheilSen Regression', TheilSenRegressor()),
    ('Bayesian Ridge Regression', BayesianRidge())
]

In [ ]:
results_table = []
mse_all = []
model_names_all = []

n_folds = 5 # Numero di fold

for name, model in models:
    print(f"Testing model: {name}")
    kfold = KFold(n_splits=n_folds, shuffle=True, random_state=42)
    pipeline = make_pipeline(StandardScaler(), model)
    r2_scores = cross_val_score(pipeline, X_train, y_train, cv=kfold, scoring="r2", n_jobs=-1)
    r2_mean = r2_scores.mean()
    mse_scores = -cross_val_score(pipeline, X_train, y_train, cv=kfold, scoring="neg_mean_squared_error", n_jobs=-1)
    mse_mean = mse_scores.mean()
    results_table.append({
        'Modello': name,
        'R2 medio': round(r2_mean, 4),
        'MSE medio': round(mse_mean, 4)
    })
    mse_all.extend(mse_scores)
    model_names_all.extend([name] * len(mse_scores))

Testing model: Linear Regression
Testing model: Ridge Regression
Testing model: Lasso Regression
Testing model: Elastic Net Regression
Testing model: Decision Tree Regression
Testing model: Random Forest Regression
Testing model: Gradient Boosting Regression
Testing model: AdaBoost Regression
Testing model: Support Vector Regression
Testing model: K-Nearest Neighbors Regression
Testing model: MLP Regression
Testing model: Huber Regression
Testing model: Quantile Regression
Testing model: RANSAC Regression
Testing model: TheilSen Regression
Testing model: Bayesian Ridge Regression


In [ ]:
results_df = pd.DataFrame(results_table).sort_values(by='R2 medio', ascending=False)
print("Risultati cross-validation:")
print(results_df)

Risultati cross-validation:
                           Modello  R2 medio  MSE medio
5         Random Forest Regression    0.9818     4.9154
9   K-Nearest Neighbors Regression    0.9798     5.5037
4         Decision Tree Regression    0.9677     8.5649
6     Gradient Boosting Regression    0.9051    25.8153
10                  MLP Regression    0.8983    27.4105
8        Support Vector Regression    0.8380    44.0842
7              AdaBoost Regression    0.7831    58.4548
1                 Ridge Regression    0.5521   121.8764
0                Linear Regression    0.5521   121.8765
15       Bayesian Ridge Regression    0.5521   121.8764
11                Huber Regression    0.5450   123.8278
2                 Lasso Regression    0.5340   126.8110
14             TheilSen Regression    0.5104   135.3232
3           Elastic Net Regression    0.4717   143.7570
13               RANSAC Regression    0.3567   157.5751
12             Quantile Regression   -0.0121   275.3862


In [ ]:
results_df_sorted = results_df.sort_values(by='MSE medio', ascending=True)

fig = go.Figure()
fig.add_trace(go.Scatter(x=results_df_sorted['Modello'],y=results_df_sorted['MSE medio'],mode='lines+markers+text',
    name='MSE medio',text=[f"{val:.2f}" for val in results_df_sorted['MSE medio']],
    textposition='top center',line=dict( width=3),yaxis='y1'))
fig.add_trace(go.Scatter(x=results_df_sorted['Modello'],y=results_df_sorted['R2 medio'],mode='lines+markers+text',
    name='R² medio',text=[f"{val:.2f}" for val in results_df_sorted['R2 medio']],
    textposition='bottom center',line=dict( width=3, dash='dot'),yaxis='y2'))

fig.update_layout(
    title={'text': "Confronto tra modelli: MSE medio e R² medio", 'x': 0.5, 'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'}},
    xaxis=dict(title="Modello"),yaxis=dict(title="MSE medio"),
    yaxis2=dict(title="R² medio",overlaying="y",side="right"),
    legend=dict(title="Metriche", orientation="h", yanchor="bottom", y=1.02, xanchor="right", x=1),
    height=600,width=1200, template='plotly_dark')

fig.show()

In [ ]:
best_model = results_df_sorted.iloc[0]
print("Il modello migliore è:\n", best_model)

Il modello migliore è:
 Modello      Random Forest Regression
R2 medio                       0.9818
MSE medio                      4.9154
Name: 5, dtype: object


#### Analisi del miglior algorimto: Random Forest

Per ulteriori approfondimenti, nel modello precedente di «Random Forest»
si è introdotta la Grid Search con cross-validation per cercare la
combinazione ottimale di iperparametri.

In [ ]:
scaler = StandardScaler()
X_train_scaled = scaler.fit_transform(X_train)
X_test_scaled = scaler.transform(X_test)

In [ ]:
rf = RandomForestRegressor(random_state=42)

param_grid = {
    'n_estimators': [10, 50, 100, 200],  # Numero di alberi
    'max_depth': [None, 10, 20, 50],  # Profondità massima degli alberi
    'min_samples_split': [2, 5, 10],  # Minimo numero di campioni per dividere un nodo
    'min_samples_leaf': [ 2, 5, 10],  # Minimo numero di campioni in una foglia
    'bootstrap': [True],  # Se usare il campionamento con sostituzione
}

grid_search = GridSearchCV(rf,param_grid,cv=3,scoring='r2',n_jobs=-1,verbose=1)
grid_search.fit(X_train_scaled, y_train)
best_rf = grid_search.best_estimator_

Fitting 3 folds for each of 144 candidates, totalling 432 fits


In [ ]:
import pickle
with open('/content/drive/MyDrive/Data Science/Data Science and Generative AI/Progetto finale/best_rf_model.pkl', 'wb') as file:
    pickle.dump(best_rf, file)


In [ ]:
with open('/content/drive/MyDrive/Data Science/Data Science and Generative AI/Progetto finale/best_rf_model.pkl', 'rb') as file:
    best_rf_model = pickle.load(file)

In [ ]:
y_pred = best_rf.predict(X_test_scaled)
mse = mean_squared_error(y_test, y_pred)
r2 = r2_score(y_test, y_pred)
rmse = np.sqrt(mse)
mae = mean_absolute_error(y_test, y_pred)

print(f"MSE: {mse:.2f}")
print(f"R^2: {r2:.2f}")
print(f"RMSE: {rmse:.2f}")
print(f"MAE: {mae:.2f}")
print("-"*134)
#print("Migliori parametri trovati:", grid_search.best_params_)
print("Migliori parametri trovati: {'bootstrap': True, 'max_depth': None, 'min_samples_leaf': 2, 'min_samples_split': 2, 'n_estimators': 200}")
print("-"*134)

MSE: 4.17
R^2: 0.98
RMSE: 2.04
MAE: 1.00
--------------------------------------------------------------------------------------------------------------------------------------
Migliori parametri trovati: {'bootstrap': True, 'max_depth': None, 'min_samples_leaf': 2, 'min_samples_split': 2, 'n_estimators': 200}
--------------------------------------------------------------------------------------------------------------------------------------


In [ ]:
fig = go.Figure()
fig.add_trace(go.Scatter(x=y_test,y=y_pred,mode='markers',name='Predizioni',marker=dict( opacity=0.6)))
min_val = min(min(y_test), min(y_pred))
max_val = max(max(y_test), max(y_pred))
fig.add_trace(go.Scatter(x=[min_val, max_val],y=[min_val, max_val],mode='lines',name='Perfetto (y = x)',line=dict(dash='dash')))

fig.update_layout(
    title={'text': "Confronto tra valori reali e predetti", 'x': 0.5, 'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'}},
    xaxis_title='Valori reali (y_test)', yaxis_title='Valori predetti (y_pred)',
    width=800,height=600,template='plotly_dark')

fig.show()

In [146]:
labels = ["Global Market Movement","Market Sentiment and Funding Rates","Crypto Search Trends and Sentiment","Commodity and Equity Market Dynamics","Commodities Price Movements","Emerging Market and Macro Trends"]

fig = make_subplots(rows=2, cols=3, subplot_titles=labels)
for i in range(6):
    row = i // 3 + 1
    col = i % 3 + 1
    fig.add_trace(go.Scatter(x=X.iloc[:, i],y=y,mode='markers',marker=dict(color='lightblue', size=4),name=labels[i],showlegend=False),row=row,col=col)

fig.update_layout(
    title={'text': "Relazione tra variabili indipendenti e variabile dipendente", 'x': 0.5, 'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'}},
    template='plotly_dark',height=700,width=1200)

fig.update_annotations(font_size=10)
fig.update_xaxes(showgrid=False)
fig.update_yaxes(showgrid=False)

fig.show()

In [ ]:
fig = make_subplots(rows=2, cols=3, subplot_titles=labels)
for i in range(6):
    row = i // 3 + 1
    col = i % 3 + 1
    fig.add_trace(go.Scatter(x=X_test[:, i],y=y_pred,mode='markers',marker=dict(color='deepskyblue', size=4),name=labels[i],showlegend=False),row=row,col=col)

fig.update_layout(
    title={'text': "Relazione tra variabili indipendenti e variabile dipendente PREDETTA", 'x': 0.5, 'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'}},
    template='plotly_dark',height=700,width=1200)

fig.update_annotations(font_size=10)
fig.update_xaxes(showgrid=False)
fig.update_yaxes(showgrid=False)

fig.show()

#### Comprendere la relazione tra target e features

In [147]:
#@title Confronto: Regressione Polinomiale vs LOWESS
grado = 3
labels = ["Global Market Movement","Market Sentiment and Funding Rates","Crypto Search Trends and Sentiment","Commodity and Equity Market Dynamics","Commodities Price Movements","Emerging Market and Macro Trends"]
fig = make_subplots(rows=2, cols=3, subplot_titles=labels)

for i in range(6):
    x = X.iloc[:, i].values.reshape(-1, 1)
    y_vals = y.values

    # -------------------------------
    # 🔸 Regressione Polinomiale
    grado = 3
    poly = PolynomialFeatures(degree=grado)
    x_poly = poly.fit_transform(x)
    model = LinearRegression().fit(x_poly, y_vals)

    x_range = np.linspace(x.min(), x.max(), 300).reshape(-1, 1)
    x_range_poly = poly.transform(x_range)
    y_pred_poly = model.predict(x_range_poly)

    # -------------------------------
    # 🟢 LOWESS (regressione locale)
    lowess = sm.nonparametric.lowess
    smoothed = lowess(y_vals, x.flatten(), frac=0.3)  # frac controlla lo smoothing

    # -------------------------------
    # Tracce
    row = i // 3 + 1
    col = i % 3 + 1

    # Dati ,marker=dict( opacity=0.6)
    fig.add_trace(go.Scatter(x=x.flatten(), y=y_vals,mode='markers', marker=dict(size=3, color='deepskyblue', opacity=0.3),name='Dati',showlegend=(i == 0)),row=row, col=col)

    # Polinomiale
    fig.add_trace(go.Scatter(x=x_range.flatten(), y=y_pred_poly,mode='lines',line=dict(color='orange', width=2),name=f'Polinomiale di grado: {grado}',showlegend=(i == 0)),row=row, col=col)
    # LOWESS
    fig.add_trace(go.Scatter(x=smoothed[:, 0], y=smoothed[:, 1],mode='lines',line=dict(color='white', width=2),name='LOWESS',showlegend=(i == 0)),row=row, col=col)

    fig.update_yaxes(title_text="Fear & Greed Index", row=row, col=col)

fig.update_layout(
    title={'text': f"Confronto: Regressione Polinomiale (grado {grado})  vs LOWESS", 'x': 0.5, 'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'}},
    template='plotly_dark',height=800,width=1500, )

fig.update_annotations(font_size=10)
fig.update_xaxes(showgrid=True)
fig.update_yaxes(showgrid=True)

fig.show()

Per comprenere la forma sono stata utilizzate la regressione polinomiale e la tecnica LOWESS

**Regressione Polinomiale**:
è una forma di regressione lineare che utilizza **potenze della variabile indipendente** per modellare relazioni curve.
Grado 2: Modella una curva a forma di U o ∩ (parabola). Grado 3+: Modella curve più complesse, ma può causare overfitting.

- **Pro:**
 - Interpretabile e parametrico.
 - Funziona bene quando la forma della curva è relativamente semplice.

- **Contro:**
 - Assume una **forma globale fissa** (es. parabola).
 - Sensibile a **outlier** e **overfitting** se il grado è troppo alto.

**LOWESS** (Locally Weighted Scatterplot Smoothing): è una tecnica di **regressione non parametrica** che costruisce una curva smooth **senza assumere una forma matematica predefinita**.

Per ogni punto \( x_i \), LOWESS:
1. Considera un numero di punti vicini (definito da `frac`).
2. Fitta una regressione lineare locale con **pesi** → i punti più vicini contano di più.
3. Ripete per ogni punto, ottenendo una curva morbida che segue i dati.

- **Pro:**
 - Si adatta **localmente** alla forma dei dati.
 - Eccellente per esplorazione visiva di tendenze complesse.
 - Funziona bene anche con **molto rumore**.

- **Contro:**
 - Più lento e computazionalmente costoso.
 - Non fornisce una formula esplicita del modello.
 - Difficile da usare per **predizioni future**.

**Quando usare quale?**

| Scenario                            | Reg. Polinomiale | LOWESS        |
|-------------------------------------|------------------|---------------|
| Relazione semplice (es. curva a U)  | ✅                | ✅             |
| Rumore elevato nei dati             | ⚠️ (sensibile)   | ✅             |
| Interpretabilità del modello        | ✅                | ⚠️ (no formula) |
| Predizioni fuori dal dataset        | ✅                | ⚠️ (non adatto) |
| Esplorazione visiva                 | ✅                | ✅             |
| Tendenza locale non uniforme        | ⚠️                | ✅             |



**Conclusione**

- Si usa la **regressione polinomiale** quando si sospetta una relazione curva ma coerente e se si vuole un modello matematico.
- Mentre, si usa **LOWESS** quando l'obiettivo è  **seguire l’andamento reale dei dati** senza imporre una forma specifica, soprattutto in fase di **esplorazione**.

##### Altri grafici prova

In [ ]:
fig = make_subplots(rows=2, cols=3, subplot_titles=labels)
for i in range(6):
    x = X.iloc[:, i].values.reshape(-1, 1)
    y_vals = y.values
    grado = 3
    poly = PolynomialFeatures(degree=grado)
    x_poly = poly.fit_transform(x)
    model = LinearRegression().fit(x_poly, y_vals)

    x_range = np.linspace(x.min(), x.max(), 300).reshape(-1, 1)
    x_range_poly = poly.transform(x_range)
    y_pred = model.predict(x_range_poly)

    row = i // 3 + 1
    col = i % 3 + 1

    fig.add_trace(go.Scatter(x=x.flatten(), y=y_vals,mode='markers',marker=dict(size=3, color='lightblue'),name='Dati', showlegend=False),row=row, col=col)

    # Curva polinomiale
    fig.add_trace(go.Scatter(x=x_range.flatten(), y=y_pred,mode='lines',line=dict(color='orange', width=2),name='Polinomiale',showlegend=False),row=row, col=col)



fig.update_layout(
    title={'text': f"Relazioni Polinomiali (grado {grado}) tra Variabili Indipendenti e y", 'x': 0.5, 'xanchor': 'center', 'font': {'size': 20, 'family': 'Arial', 'weight': 'bold'}},
    template='plotly_dark',height=700,width=1200)

fig.update_annotations(font_size=10)
fig.update_xaxes(showgrid=True)
fig.update_yaxes(showgrid=True)

fig.show()

In [ ]:
lowess = sm.nonparametric.lowess
smoothed = lowess(y_vals, x.flatten(), frac=0.3)  # frac = quanto smoothing

fig = go.Figure()
fig.add_trace(go.Scatter(x=x.flatten(), y=y_vals, mode='markers', name='Dati', marker=dict(color='lightblue')))
fig.add_trace(go.Scatter(x=smoothed[:, 0], y=smoothed[:, 1], mode='lines', name='LOWESS', line=dict(color='lime')))
fig.update_layout(template='plotly_dark', title='LOWESS Fit', title_x=0.5)
fig.show()

## Conclusioni

Il **Fear and Greed Index** è un indicatore che misura il sentiment di mercato, oscillando tra due estremi: paura (bassi livelli) e avidità (alti livelli). Esso è tendenzialmente influenzato da diverse variabili di mercato, come ad esempio:



1.   **Global Market Movement**, si osserva un'**onda tendenzialmente crescente**, suggerendo che i movimenti globali dei mercati influenzano in modo dinamico il sentiment, con un focus crescente sull’andamento complessivo dei mercati finanziari.

2.   **Market Sentiment and Funding Rates** e **Crypto Search Trends and Sentiment** tendono a **aumentare** il Fear and Greed Index, poiché un sentiment positivo e la crescita delle ricerche sugli asset digitali indicano un clima di **ottimismo**.
  
4. **Commodity and Equity Market Dynamics** mostra una **curva a U rovesciata**, dove in periodi di alta volatilità o turbolenze, il sentiment di paura aumenta, mentre in fasi di stabilità cresce l'avidità.

5. **Commodities Price Movements** tende a **scendere** parallelamente al Fear and Greed Index, suggerendo che fluttuazioni significative positive nei prezzi delle materie prime, spesso legate a periodi di incertezza, spingano gli investitori verso la paura.

6. Infine, con **Emerging Market and Macro Trends** generano una **curva a U tendenzialmente piatta**, con i movimenti nei mercati emergenti e nei dati macroeconomici che mostrano una relazione meno definita, ma comunque correlata a cicli economici e trend globali.